In [ ]:
import os
import random
import shutil
from pathlib import Path

import torch
from diffusers import DiffusionPipeline
from google.colab import files

# =====================================================
# CONFIG
# =====================================================

START_BATCH = 4      # Change to continue later
END_BATCH = 9

PROMPTS_PER_BATCH = 5
IMAGES_PER_PROMPT = 200

# =====================================================
# LOAD MODEL
# =====================================================

print("Loading SDXL...")

pipe = DiffusionPipeline.from_pretrained(
    "stabilityai/stable-diffusion-xl-base-1.0",
    torch_dtype=torch.float16,
    use_safetensors=True
)

pipe = pipe.to("cuda")

negative_prompt = (
    "cartoon, anime, illustration, painting, drawing, "
    "cgi, 3d render, doll, blurry, low quality, "
    "deformed, extra fingers, extra eyes"
)

# =====================================================
# PUT YOUR 50 PROMPTS HERE
# =====================================================

prompts = [
    "ultra realistic DSLR portrait photograph, young woman with freckles, soft window light.",
    "ultra realistic DSLR portrait photograph, elderly man with deep wrinkles, wearing a flat cap.",
    "ultra realistic DSLR portrait photograph, middle-aged woman with curly grey hair, warm smile.",
    "ultra realistic DSLR portrait photograph, teenage boy with acne, messy brown hair, neutral expression.",
    "ultra realistic DSLR portrait photograph, bald man with a close-trimmed beard, studio lighting.",
    "ultra realistic DSLR portrait photograph, girl with blue eyes, long straight black hair, looking sideways.",
    "ultra realistic DSLR portrait photograph, man in his 30s with glasses, short stubble, dimple chin.",
    "ultra realistic DSLR portrait photograph, elderly woman with silver hair, laughing, shallow depth of field.",
    "ultra realistic DSLR portrait photograph, young adult with vitiligo, direct sunlight, no makeup.",
    "ultra realistic DSLR portrait photograph, man with prominent nose, receding hairline, serious gaze.",
    "ultra realistic DSLR portrait photograph, woman with braided red hair, green eyes, slight smirk.",
    "ultra realistic DSLR portrait photograph, boy with missing front tooth, dirty blond hair, freckled cheeks.",
    "ultra realistic DSLR portrait photograph, man with cleft lip scar, short dark hair, five o'clock shadow.",
    "ultra realistic DSLR portrait photograph, woman with high cheekbones, tight bun, business attire.",
    "ultra realistic DSLR portrait photograph, man with shaved head and tribal tattoo, harsh shadowing.",
    "ultra realistic DSLR portrait photograph, little girl with pigtails, rosy cheeks, missing tooth smile.",
    "ultra realistic DSLR portrait photograph, man with thick ginger beard, bald head, squinting eyes.",
    "ultra realistic DSLR portrait photograph, woman with undercut, silver nose ring, direct eye contact.",
    "ultra realistic DSLR portrait photograph, man with unibrow and thin lips, hooded eyes.",
    "ultra realistic DSLR portrait photograph, woman with scars on forehead, short wavy hair, pensive.",
    "ultra realistic DSLR portrait photograph, man with double chin, balding, wearing reading glasses.",
    "ultra realistic DSLR portrait photograph, woman with beauty mark near lip, side lighting.",
    "ultra realistic DSLR portrait photograph, man with cleft chin, slicked-back hair, blue suit.",
    "ultra realistic DSLR portrait photograph, woman with droopy eyelids, thin lips, mole on cheek.",
    "ultra realistic DSLR portrait photograph, man with crooked smile, large ears, casual t-shirt.",
    "ultra realistic DSLR portrait photograph, woman with widow's peak, strong jawline, direct flash.",
    "ultra realistic DSLR portrait photograph, man with lazy eye, unshaven, looking down.",
    "ultra realistic DSLR portrait photograph, woman with ashy blonde hair, distinct laugh lines, cozy sweater.",
    "ultra realistic DSLR portrait photograph, man with hooked nose, thick eyebrows, white polo shirt.",
    "ultra realistic DSLR portrait photograph, woman with round face, double pierced ears, gentle expression.",
    "ultra realistic DSLR portrait photograph, man with scar above eyebrow, crew cut, stoic.",
    "ultra realistic DSLR portrait photograph, woman with gap-toothed smile, curly ponytail, outdoor light.",
    "ultra realistic DSLR portrait photograph, man with goatee, receding hairline, looking up.",
    "ultra realistic DSLR portrait photograph, woman with prominent Adam's apple, side part, soft smile.",
    "ultra realistic DSLR portrait photograph, man with flat nose, wide-set eyes, stubble, hoodie.",
    "ultra realistic DSLR portrait photograph, woman with pointed chin, deep dimples, messy bun.",
    "ultra realistic DSLR portrait photograph, man with furrowed brow, heavy eyelids, wrinkled polo.",
    "ultra realistic DSLR portrait photograph, woman with long neck, beauty spot, hair tucked behind ear.",
    "ultra realistic DSLR portrait photograph, man with bushy mustache, rosacea cheeks, hat.",
    "ultra realistic DSLR portrait photograph, woman with narrow face, thin eyebrows, pearl earrings.",
    "ultra realistic DSLR portrait photograph, man with broken nose, tired eyes, plain background.",
    "ultra realistic DSLR portrait photograph, woman with prominent forehead, small mouth, three-quarter view.",
    "ultra realistic DSLR portrait photograph, man with cleft palate scar, short afro, serious.",
    "ultra realistic DSLR portrait photograph, woman with double crown, wispy baby hairs, laughing.",
    "ultra realistic DSLR portrait photograph, man with receding jaw, acne scars, side lighting.",
    "ultra realistic DSLR portrait photograph, woman with monobrow, short pixie cut, neutral mouth.",
    "ultra realistic DSLR portrait photograph, man with square jaw, thin beard, looking straight.",
    "ultra realistic DSLR portrait photograph, woman with teardrop tattoo under eye, severe expression.",
    "ultra realistic DSLR portrait photograph, man with mole on his nose, thinning hair, grey t-shirt.",
    "ultra realistic DSLR portrait photograph, woman with long philtrum, straight hair, overcast lighting.",
]

assert len(prompts) == 50

# =====================================================
# ROOT
# =====================================================

ROOT = Path("SDXL_AIface_ds")
ROOT.mkdir(exist_ok=True)

# =====================================================
# GENERATE
# =====================================================

for batch in range(START_BATCH, END_BATCH + 1):

    print(f"\n===== BATCH {batch} =====")

    batch_dir = ROOT / f"batch_{batch}"
    batch_dir.mkdir(parents=True, exist_ok=True)

    batch_prompts = prompts[
        batch * PROMPTS_PER_BATCH:
        (batch + 1) * PROMPTS_PER_BATCH
    ]

    img_num = 0

    for prompt in batch_prompts:

        for _ in range(IMAGES_PER_PROMPT):

            seed = random.randint(0, 2**32 - 1)

            generator = torch.Generator(
                device="cuda"
            ).manual_seed(seed)

            image = pipe(
                prompt,
                negative_prompt=negative_prompt,
                generator=generator,
                height=512,
                width=512,
                num_inference_steps=10,
                guidance_scale=7.5
            ).images[0]

            image.save(
                batch_dir /
                f"img_{img_num:04d}.png"
            )

            img_num += 1

            if img_num % 100 == 0:
                print(
                    f"Batch {batch}: "
                    f"{img_num}/4000"
                )

    print("Creating zip...")

    shutil.make_archive(
        f"batch_{batch}",
        "zip",
        batch_dir
    )

    print(f"batch_{batch}.zip created")

    files.download(
        f"batch_{batch}.zip"
    )

    print(
        f"\nFinished batch {batch}"
        f"\nTo continue later:"
        f"\nSTART_BATCH = {batch + 1}"
    )

    break

Flax classes are deprecated and will be removed in Diffusers v1.0.0. We recommend migrating to PyTorch classes or pinning your version of Diffusers.
Flax classes are deprecated and will be removed in Diffusers v1.0.0. We recommend migrating to PyTorch classes or pinning your version of Diffusers.


Loading SDXL...


/usr/local/lib/python3.12/dist-packages/huggingface_hub/utils/_auth.py:112: UserWarning: 
The secret `HF_TOKEN` does not exist in your Colab secrets.
To authenticate with the Hugging Face Hub, create a token in your settings tab (https://huggingface.co/settings/tokens), set it as secret in your Google Colab and restart your session.
You will be able to reuse this secret in all of your notebooks.
Please note that authentication is recommended but still optional to access public models or datasets.
  warnings.warn(


Loading pipeline components...:   0%|          | 0/7 [00:00<?, ?it/s]

Loading weights:   0%|          | 0/196 [00:00<?, ?it/s]

...

  0%|          | 0/10 [00:00<?, ?it/s]

Batch 4: 1000/4000
Creating zip...
batch_4.zip created


<IPython.core.display.Javascript object>

<IPython.core.display.Javascript object>


Finished batch 4
To continue later:
START_BATCH = 5
